### Nelson-Siegel-Svensson and CubicSpline Methodology for BDT Inputs

In [2]:
import warnings
import numpy as np
import pandas as pd
from scipy.optimize import minimize
import statsmodels.api as sm
from scipy.interpolate import CubicSpline
import matplotlib.pyplot as plt
from IPython.display import display, HTML
from matplotlib.animation import FuncAnimation

In [7]:
df_treasury = pd.read_csv('daily-treasury-rates.csv')
df_fed = pd.read_csv('FEDFUNDS.csv')

df_treasury['Date'] = pd.to_datetime(df_treasury['Date'])
df_treasury = df_treasury.set_index('Date')

df_fed['observation_date'] = pd.to_datetime(df_fed['observation_date'])
df_fed = df_fed.set_index('observation_date')
df_fed = df_fed.rename(columns={'FEDFUNDS': 'FED'})

df_combined = df_treasury.join(df_fed[['FED']], how='outer')
df_combined['FED'] = df_combined['FED'].ffill()
df_combined = df_combined.dropna(subset=['1 Mo', 'FED']).sort_index(ascending=False)

print(f"Combined rows: {len(df_combined)}")
display(df_combined.head())

Combined rows: 4160


,1 Mo,1.5 Month,2 Mo,3 Mo,4 Mo,6 Mo,1 Yr,2 Yr,3 Yr,5 Yr,7 Yr,10 Yr,20 Yr,30 Yr,FED
Date,,,,,,,,,,,,,,,
2026-08-19,3.77,3.77,3.81,3.86,3.88,3.94,4.00,4.19,4.25,4.35,4.48,4.65,5.17,5.19,3.63
2026-08-18,3.78,3.78,3.82,3.86,3.88,3.94,3.99,4.19,4.26,4.37,4.53,4.71,5.28,5.28,3.63
2026-08-17,3.79,3.80,3.82,3.87,3.89,3.95,4.00,4.19,4.25,4.38,4.54,4.72,5.30,5.31,3.63
2026-08-14,3.79,3.80,3.81,3.86,3.88,3.95,3.98,4.17,4.24,4.36,4.51,4.68,5.25,5.25,3.63
2026-08-13,3.79,3.79,3.81,3.87,3.88,3.94,3.97,4.15,4.20,4.32,4.47,4.63,5.20,5.21,3.63


In [8]:
class NelsonSiegelSvensson:
    """Nelson-Siegel-Svensson (NSS) Yield Curve Model."""
    def __init__(self):
        self.params = np.zeros(6)
        self.is_fitted = False

    def _nss_formula(self, t: np.ndarray, params: np.ndarray) -> np.ndarray:
        b0, b1, b2, b3, tau1, tau2 = params
        t = np.maximum(t, 1e-6)
        
        term1 = (1 - np.exp(-t / tau1)) / (t / tau1)
        term2 = term1 - np.exp(-t / tau1)
        term3 = ((1 - np.exp(-t / tau2)) / (t / tau2)) - np.exp(-t / tau2)
        
        return b0 + b1 * term1 + b2 * term2 + b3 * term3

    def _objective(self, params: np.ndarray, maturities: np.ndarray, yields: np.ndarray) -> float:
        predictions = self._nss_formula(maturities, params)
        return np.sum((predictions - yields) ** 2)

    def fit(self, maturities: np.ndarray, yields: np.ndarray) -> "NelsonSiegelSvensson":
        maturities, yields = np.asarray(maturities, dtype=float), np.asarray(yields, dtype=float)
        guess = np.array([yields[-1], yields[0] - yields[-1], 0.0, 0.0, 1.0, 1.0])
        bounds = ((None, None), (None, None), (None, None), (None, None), (0.01, None), (0.01, None))

        result = minimize(
            self._objective, x0=guess, args=(maturities, yields),
            method='L-BFGS-B', bounds=bounds
        )

        if not result.success:
            print(f"Warning: Calibration did not fully converge. {result.message}")

        self.params = result.x
        self.is_fitted = True
        return self

    def predict(self, maturities: np.ndarray) -> np.ndarray:
        if not self.is_fitted:
            raise ValueError("Model must be fitted first.")
        return self._nss_formula(np.asarray(maturities, dtype=float), self.params)

In [9]:
warnings.filterwarnings('ignore')

subset_df = df_combined.head(2520).iloc[::21].iloc[::-1]
tenors = np.array([1/12, 1.5/12, 2/12, 3/12, 4/12, 6/12, 1, 2, 3, 5, 7, 10, 20, 30])
continuous_tenors = np.linspace(0.1, 30, 300)

fig, ax = plt.subplots(figsize=(10, 5))
ax.set_xlim(0, 31)
ax.set_ylim(0, 6.0)
ax.set_xlabel("Maturity (Years)")
ax.set_ylabel("Yield (%)")
ax.grid(True, linestyle=':', alpha=0.6)

scatter = ax.scatter([], [], color='#dc2626', zorder=5, label='Actual Quotes')
line, = ax.plot([], [], color='#0284c7', linewidth=2, label='NSS Curve')
title = ax.set_title("")
ax.legend(loc="upper right")

anim_nss_model = NelsonSiegelSvensson()

def init():
    scatter.set_offsets(np.empty((0, 2)))
    line.set_data([], [])
    title.set_text("")
    return scatter, line, title

def update(frame):
    date = subset_df.index[frame].date()
    yields = subset_df.iloc[frame, :-1].values.astype(float)
    
    valid_mask = ~np.isnan(yields)
    valid_tenors = tenors[valid_mask]
    valid_yields = yields[valid_mask]
    
    anim_nss_model.fit(valid_tenors, valid_yields)
    smooth_curve = anim_nss_model.predict(continuous_tenors)
    
    scatter.set_offsets(np.c_[valid_tenors, valid_yields])
    line.set_data(continuous_tenors, smooth_curve)
    title.set_text(f"Nelson-Siegel-Svensson Yield Curve ({date})")
    
    current_max = np.nanmax(yields)
    if current_max > ax.get_ylim()[1] - 0.5:
        ax.set_ylim(0, current_max + 1.0)
        
    return scatter, line, title

anim = FuncAnimation(fig, update, frames=len(subset_df), init_func=init, blit=False, interval=100)
plt.close(fig) 
HTML(anim.to_jshtml())

In [10]:
fig_cs, ax_cs = plt.subplots(figsize=(10, 5))
ax_cs.set_xlim(0, 31)
ax_cs.set_ylim(0, 6.0)
ax_cs.set_xlabel("Maturity (Years)")
ax_cs.set_ylabel("Yield (%)")
ax_cs.grid(True, linestyle=':', alpha=0.6)

scatter_cs = ax_cs.scatter([], [], color='#dc2626', zorder=5, label='Actual Quotes')
line_cs, = ax_cs.plot([], [], color='#0284c7', linewidth=2, label='Cubic Spline')
title_cs = ax_cs.set_title("")
ax_cs.legend(loc="upper right")

def init_cs():
    scatter_cs.set_offsets(np.empty((0, 2)))
    line_cs.set_data([], [])
    title_cs.set_text("")
    return scatter_cs, line_cs, title_cs

def update_cs(frame):
    date = subset_df.index[frame].date()
    yields = subset_df.iloc[frame, :-1].values.astype(float)
    
    valid_mask = ~np.isnan(yields)
    valid_tenors = tenors[valid_mask]
    valid_yields = yields[valid_mask]
    
    cs = CubicSpline(valid_tenors, valid_yields, bc_type='natural')
    smooth_curve = cs(continuous_tenors)
    
    scatter_cs.set_offsets(np.c_[valid_tenors, valid_yields])
    line_cs.set_data(continuous_tenors, smooth_curve)
    title_cs.set_text(f"Cubic Spline Yield Curve ({date})")
    
    current_max = np.nanmax(yields)
    if current_max > ax_cs.get_ylim()[1] - 0.5:
        ax_cs.set_ylim(0, current_max + 1.0)
        
    return scatter_cs, line_cs, title_cs

anim_cs = FuncAnimation(fig_cs, update_cs, frames=len(subset_df), init_func=init_cs, blit=False, interval=100)
plt.close(fig_cs)
HTML(anim_cs.to_jshtml())

# Prepare BDT Inputs

In [11]:
target_date = df_combined.index[0]
tenors = np.array([1/12, 1.5/12, 2/12, 3/12, 4/12, 6/12, 1, 2, 3, 5, 7, 10, 20, 30])
bdt_maturities = np.arange(1.0, 16.0, 1.0)
lookback = 504

raw_yields = df_combined.iloc[0, :-1].values.astype(float) / 100.0 
valid_mask = ~np.isnan(raw_yields)

nss_today = NelsonSiegelSvensson().fit(tenors[valid_mask], raw_yields[valid_mask])
bdt_spot_yields = nss_today.predict(bdt_maturities)

historical_yields = df_combined.head(lookback + 1).iloc[:, :-1].values.astype(float) / 100.0
nss_hist_curves = np.zeros((len(historical_yields), len(bdt_maturities)))
model = NelsonSiegelSvensson()

for i, y_row in enumerate(historical_yields):
    m = ~np.isnan(y_row)
    model.fit(tenors[m], y_row[m])
    nss_hist_curves[i] = model.predict(bdt_maturities)

nss_hist_curves = np.maximum(nss_hist_curves, 1e-4)
log_returns = np.log(nss_hist_curves[:-1] / nss_hist_curves[1:])
bdt_yield_vols = np.nanstd(log_returns, axis=0) * np.sqrt(252)
bdt_yield_vols[0] = np.nan

print(f"--- BDT Inputs Prepared ({target_date.date()}) | NSS Model ---")
print("Maturity (Yrs) | Spot Yield (NSS) | Yield Vol (NSS Dynamics)")
print("-" * 62)
for m, y, v in zip(bdt_maturities, bdt_spot_yields, bdt_yield_vols):
    print(f"{m:^14.1f} | {y:^16.2%} | {'NaN' if np.isnan(v) else f'{v:^24.2%}'}")

--- BDT Inputs Prepared (2026-08-19) | NSS Model ---
Maturity (Yrs) | Spot Yield (NSS) | Yield Vol (NSS Dynamics)
--------------------------------------------------------------
     1.0       |      3.90%       | NaN
     2.0       |      4.09%       |          20.86%         
     3.0       |      4.28%       |          21.70%         
     4.0       |      4.43%       |          23.68%         
     5.0       |      4.54%       |          24.34%         
     6.0       |      4.63%       |          23.63%         
     7.0       |      4.69%       |          22.20%         
     8.0       |      4.74%       |          20.59%         
     9.0       |      4.78%       |          19.15%         
     10.0      |      4.81%       |          18.00%         
     11.0      |      4.84%       |          17.20%         
     12.0      |      4.86%       |          16.72%         
     13.0      |      4.88%       |          16.49%         
     14.0      |      4.89%       |          16.46%

In [ ]:
raw_yields = df_combined.iloc[0, :-1].values.astype(float) / 100.0 
valid_mask = ~np.isnan(raw_yields)

cs_today = CubicSpline(tenors[valid_mask], raw_yields[valid_mask], bc_type='natural')
bdt_spot_yields = cs_today(bdt_maturities)

historical_yields = df_combined.head(lookback + 1).iloc[:, :-1].values.astype(float) / 100.0
spline_hist_curves = np.zeros((len(historical_yields), len(bdt_maturities)))

for i, y_row in enumerate(historical_yields):
    m = ~np.isnan(y_row)
    cs = CubicSpline(tenors[m], y_row[m], bc_type='natural')
    spline_hist_curves[i] = cs(bdt_maturities)

spline_hist_curves = np.maximum(spline_hist_curves, 1e-4)
log_returns = np.log(spline_hist_curves[:-1] / spline_hist_curves[1:])
bdt_yield_vols = np.nanstd(log_returns, axis=0) * np.sqrt(252)
bdt_yield_vols[0] = np.nan

print(f"--- BDT Inputs Prepared ({target_date.date()}) | Cubic Spline ---")
print("Maturity (Yrs) | Spot Yield (Spline) | Yield Vol (Spline Dynamics)")
print("-" * 65)
for m, y, v in zip(bdt_maturities, bdt_spot_yields, bdt_yield_vols):
    print(f"{m:^14.1f} | {y:^19.2%} | {'NaN' if np.isnan(v) else f'{v:^27.2%}'}")

--- BDT Inputs Prepared (2026-08-19) | Cubic Spline ---
Maturity (Yrs) | Spot Yield (Spline) | Yield Vol (Spline Dynamics)
-----------------------------------------------------------------
     1.0       |        4.00%        | NaN
     2.0       |        4.19%        |           21.26%           
     3.0       |        4.25%        |           21.32%           
     4.0       |        4.29%        |           21.14%           
     5.0       |        4.35%        |           20.86%           
     6.0       |        4.42%        |           20.46%           
     7.0       |        4.48%        |           19.81%           
     8.0       |        4.54%        |           19.10%           
     9.0       |        4.59%        |           18.31%           
     10.0      |        4.65%        |           17.64%           
     11.0      |        4.71%        |           17.15%           
     12.0      |        4.77%        |           16.78%           
     13.0      |        4.83%  